<a href="https://colab.research.google.com/github/synthesis0x42/non-markovian-AI/blob/main/AI_for_Non_Markovianity.ipynb" target="_parent"><img src="https://colab.research.google.com/assets/colab-badge.svg" alt="Open In Colab"/></a>

In [ ]:
!pip install qutip
!pip install scikit-learn
!pip install cvnn[full]

import numpy as np
from os.path import dirname, join as pjoin
import pandas as pd
from itertools import permutations, combinations_with_replacement
import itertools as it
import json
from matplotlib import pyplot as plt
import seaborn as sns
import scipy.io as sio
from qutip import *
from qutip.qip.operations import rx, ry, rz, rotation
import scipy.io
import tensorflow as tf

sns.set()


In [ ]:
xp = (qutip.basis(2, 0) + (1+0j)*qutip.basis(2, 1)).unit()
xm = (qutip.basis(2, 0) - (1+0j)*qutip.basis(2, 1)).unit()
yp = (qutip.basis(2, 0) + (0+1j)*qutip.basis(2, 1)).unit()
ym = (qutip.basis(2, 0) - (0+1j)*qutip.basis(2, 1)).unit()
zp = (qutip.basis(2, 0) + (0+0j)*qutip.basis(2, 1)).unit()
zm = (qutip.basis(2, 1) + (0+0j)*qutip.basis(2, 1)).unit()
states = [xp, xm, yp, ym, zp, zm]
rhos = [xp*xp.dag(), xm*xm.dag(), yp*yp.dag(), ym*ym.dag(), zp*zp.dag(), zm*zm.dag()]
sigs = [sigmax(), sigmay(), sigmaz(), qeye(2)]



def generateData(W):
  ## put this fn inside the pickle for loop , use raw_data = GenerateData for each W
  ## also write tomos = exp2probs(raw_data, runlabel=None) inside the pickle forloop too
  ## since you need to generate tomos0, tomos1, etcetc. tomos are the features
    '''
    Given a W matrix, generate sample count data
    '''

    # encode states and measurements numerically to index into basis
    labels_i = [k for k in it.product(range(6), range(3),range(6),range(3))]
    c = [[0,1],[2,3],[4,5],[4,5]]  # [[xp,xm],[yp,ym],[zp,zm],[zp,zm]]
    Ls = ['xp','xm','yp','ym','zp','zm']
    Lo = ['x','y','z']
    data = {}
    for s1,o1,s2,o2 in labels_i:
        label = f'{Ls[s1]},{Lo[o1]},{Ls[s2]},{Lo[o2]}'
        counts = {}
        # random number of tot counts around 8000
        #tot = int(8000+(np.random.random()*200-100))
        tot=8000
        #pac=wtrace(W/4, rhos[s1].trans(), qeye(2), rhos[s2].trans(), qeye(2) )

        for m1,m2 in it.product(range(2),repeat=2):
            # if o1=1,m1=2, c[1]=(2,3)  c[o1][m1]=3
            omega=tensor(rhos[s1].trans(), rhos[c[o1][m1]], rhos[s2].trans(), rhos[c[o2][m2]]).full()
            #omega=tensor(rhos[s1], rhos[c[o1][m1]], rhos[s2], rhos[c[o2][m2]]).full()
            #counts[f'{m1}{m2}']=int(np.real(np.trace(np.matmul(W.full(),omega)))*tot)
            counts[f'{m1}{m2}']=np.real(np.trace(np.matmul(W,omega)))*tot
        totp = counts['00']+counts['01']+counts['10']+counts['11']
        for k in counts:
            counts[k]=counts[k]*tot/totp
        data[label]=counts
    return data

def exp2probs(raw, runlabel):
    '''
    Conversion utility for Tyler's data to a straight list of probabilies
    Reads in data in form
    {"xp,x,xp,x": {"00": 7917, "01": 13, "10": 31, "11": 29} ...
    and generates tomography data in form
    (0, 0, 0, 0) 0.9908635794743429
    (0, 0, 0, 1) 0.0016270337922403004
    :

    '''
    Km = {'x0':0,'x1':1,'y0':2,'y1':3,'z0':4,'z1':5}
    Ks = {'xp':0,'xm':1,'yp':2,'ym':3,'zp':4,'zm':5}
    labels=[]
    probs=[]

    if runlabel is None:
        data = raw

    else:
        data = raw[runlabel]

    for key in data:
        counts = data[key]
        keys=key.split(',')
        # e.g. keys = ['xp','y','yp','z']
        # e.g. counts looks like {"00": 7917, "01": 13, "10": 31, "11": 29}
        #tot=0
        #for c in counts.values():
        #    tot+=c
        tot = counts['00']+counts['01']+counts['10']+counts['11']

        for l1,l2 in ['00','01','10','11']:
            lab= (Ks[keys[0]], Km[keys[1]+l1], Ks[keys[2]], Km[keys[3]+l2])
            # key = ('xp','y0','yp','z0') -> (0,2,2,4) = lab
            prob = counts[l1+l2]/tot
            labels.append(lab)
            probs.append(prob)
    #return pd.Series(probs)
    return pd.DataFrame(probs,index=labels)



In [ ]:

var = locals() ## locals is all the local vars

from scipy.io import loadmat ## loads matrices
matfile = loadmat('Wexp_uq_9797.mat')
matfile["B"]

#locals().update(tomos)


## You'll have W0, W1, W2, ... W999

array([[array([[ 8.37401622e-01+0.00000000e+00j,  2.73601346e-02-2.09287917e-02j,
                -2.21717274e-02-4.61247750e-03j,  6.44930063e-01-2.81564053e-01j,
                 6.99270357e-02-7.05553121e-02j, -4.60483626e-03-1.55825806e-02j,
                -7.26092944e-03-7.09223197e-04j,  3.68263386e-02-8.99216433e-02j,
                 5.97752664e-03-8.85177848e-03j,  1.64403776e-02+1.06617041e-03j,
                 1.25930557e-02+5.29274849e-03j, -4.58179965e-02+2.67233995e-02j,
                 5.27939505e-01-2.11153052e-01j, -3.60225031e-03-2.44938562e-02j,
                -5.04002677e-04+5.61269791e-03j,  2.72376334e-01-2.61075469e-01j],
               [ 2.73601346e-02+2.09287917e-02j,  5.40646734e-02+0.00000000e+00j,
                 1.06526972e-02+1.05398586e-02j,  2.21717274e-02+4.61247750e-03j,
                 1.59986161e-02+5.82604145e-03j, -1.46990367e-02+2.47675704e-02j,
                -1.38538298e-02+7.63738403e-03j,  7.26092944e-03+7.09223197e-04j,
               

In [ ]:
var_holder = {} ## holds variables
tomos = {} ## stores just the tomography values with all the keys etc
for i in range(1000): ## the 5 minute hell loop
  tomostr = "tomos"+str(i)
  mat = matfile["B"][i][0]
  var_holder[tomostr]=[]
  #var_holder[tomostr].append([exp2probs(generateData(mat),runlabel=None).keys, exp2probs(generateData(mat),runlabel=None).values])
  a = exp2probs(generateData(mat),runlabel=None)
  var_holder[tomostr].append(a.values.squeeze().tolist())
  tomos[tomostr] = exp2probs(generateData(mat),runlabel=None)
locals().update(var_holder)
tomos = pd.DataFrame(tomos) ## turns it into a dataframe


In [ ]:
type(var_holder.values()) ##test

dict_values

In [ ]:
## create a for loop that opens all the npy files
## example code:
# Open a file and use dump()
var = locals() ## locals is all the local vars
with open('negs_9797.npy', 'rb') as f:
  #string = "negs_9797"
  #var_holder[string] = f ## for i = 0 create W0
  #np.dump(var[string], f)
  # stroW+str(i) ## ?????????!?!?1/?!?!?!?!?!?1?!?!?
  neg = np.load(f)
  print(neg)



with open('sqrtvne_9797.npy', 'rb') as f:
  #string = "negs_9797"
  #var_holder[string] = f ## for i = 0 create W0
  #np.dump(var[string], f)
  # stroW+str(i) ## ?????????!?!?1/?!?!?!?!?!?1?!?!?
  vne = np.load(f)

for i in range(1000):
  tomostr = "tomos"+str(i)
  var_holder[tomostr].append(neg[i])
  var_holder[tomostr].append(vne[i])


locals().update(var_holder)


[0.08457479 0.09017716 0.0848389  0.08831594 0.08514241 0.08260109
 0.09202496 0.09215392 0.07592692 0.08145015 0.08725974 0.09111308
 0.08206568 0.090624   0.08608714 0.0857224  0.08749294 0.08267273
 0.08611905 0.09166558 0.07766271 0.08629857 0.09114147 0.08852299
 0.07911314 0.08896406 0.08534267 0.09672002 0.08945132 0.08482089
 0.08410855 0.08614835 0.08616763 0.09007901 0.08655989 0.08768741
 0.08289724 0.0834158  0.0960518  0.09242299 0.08642361 0.08847829
 0.08448558 0.08986952 0.08368868 0.07754889 0.09120772 0.08289965
 0.0886896  0.08902523 0.08937173 0.09594998 0.082563   0.0955107
 0.08580417 0.08814752 0.08949933 0.08268865 0.08867502 0.0810804
 0.08482831 0.08932477 0.09049959 0.08396455 0.08778181 0.08671027
 0.08557478 0.08155416 0.0878017  0.08919268 0.08922558 0.08501976
 0.08427852 0.08704794 0.08855532 0.09121834 0.08418744 0.08469911
 0.09190954 0.08550431 0.08944781 0.08939574 0.08938138 0.08897671
 0.0823123  0.08568357 0.09037961 0.08884156 0.08398976 0.088825

In [ ]:
from sklearn.model_selection import train_test_split
info_df = pd.DataFrame(data=var_holder.values(),index=var_holder.keys(),columns=["tomography","negativity","sqrt vne"])
info_df

,tomography,negativity,sqrt vne
tomos0,"[0.7271710413290804, 0.12068915900936007, 0.09...",0.084575,0.167091-0.000000j
tomos1,"[0.7263817135710201, 0.1229084099272841, 0.087...",0.090177,0.158738-0.000000j
tomos2,"[0.729040603453297, 0.11723843460069559, 0.093...",0.084839,0.165868-0.000000j
tomos3,"[0.729405753813405, 0.11714046718796117, 0.089...",0.088316,0.150213-0.000000j
tomos4,"[0.7344202534809818, 0.11038894618735585, 0.08...",0.085142,0.160906-0.000000j
...,...,...,...
tomos995,"[0.7269866007033317, 0.1207086759717156, 0.086...",0.083767,0.160747-0.000000j
tomos996,"[0.7312659938219579, 0.11993173352225504, 0.08...",0.078709,0.158643-0.000000j
tomos997,"[0.7331292141509907, 0.114590065418782, 0.0869...",0.091499,0.162793-0.000000j
tomos998,"[0.7318043040905696, 0.11777218277411662, 0.08...",0.093822,0.161008-0.000000j


In [ ]:
X = info_df["tomography"].values.tolist() ## turns it to a list so that it can be processed in a tensor
y = info_df[["negativity","sqrt vne"]].values.tolist()

X_train, X_test, y_train, y_test = train_test_split(np.array(X),np.array(y),test_size=0.4,random_state=69)

In [ ]:
from tensorflow.keras.models import Sequential
from tensorflow.keras.layers import Dense
## help(Sequential) or help(Dense) is vv nice
## anyway this is just importing the sequential model and dense

from tensorflow.keras.callbacks import EarlyStopping
early_stop = EarlyStopping(monitor="val_loss",mode="min",verbose=1,patience=25)
from tensorflow.keras.layers import Dropout

#import cvnn.layers as complex_layers


In [ ]:
model = Sequential()
model.add(Dense(2)) ## adds layer
model.add(Dropout(0.5))
model.add(Dense(2))
model.add(Dropout(0.5)) ## to prevent overfit

#model.add(Dense(units=40))
model.compile(optimizer="rmsprop",loss="mse")

his = model.fit(x=X_train,y=y_train,epochs=75,callbacks=[early_stop])

## this bit shows cost fn

loss_df = pd.DataFrame(model.history.history)
loss_df.plot()

NameError: ignored

In [ ]:
model.predict(X_test) ## predicts y_test

13/13 [==============================] - 0s 1ms/step


array([[0.08858211, 0.16015528],
       [0.08877267, 0.1603788 ],
       [0.08851951, 0.1602983 ],
       [0.08882475, 0.16021234],
       [0.08861014, 0.16039708],
       [0.0886043 , 0.16016239],
       [0.08868798, 0.16032061],
       [0.08861832, 0.16014051],
       [0.08876207, 0.16020033],
       [0.08851631, 0.16021703],
       [0.08851408, 0.16028126],
       [0.08865735, 0.16015434],
       [0.08850095, 0.16022536],
       [0.08855478, 0.16026366],
       [0.08870355, 0.16015461],
       [0.08859476, 0.16022898],
       [0.08855549, 0.1601499 ],
       [0.08873001, 0.16025235],
       [0.0886027 , 0.16019066],
       [0.08877825, 0.16035645],
       [0.08870036, 0.1603053 ],
       [0.08860332, 0.16022143],
       [0.08870623, 0.16019928],
       [0.08860549, 0.16029437],
       [0.08861694, 0.16027956],
       [0.08850023, 0.16034687],
       [0.08858143, 0.16035163],
       [0.08882634, 0.16024868],
       [0.08860854, 0.16008978],
       [0.08851803, 0.16036353],
       [0.

In [ ]:
model.evaluate(X_test,y_test) ## evaluates avg mean squared error

13/13 [==============================] - 0s 1ms/step - loss: 1.5909e-05


1.590892679814715e-05

from here on it's just the pickle test thing from day 3

In [ ]:
## fake data :)
## example pickle code:
# Open a file and use dump()
#import pickle
#var = locals() ## locals is all the local vars
#g = 10
#var_holder = {}

#for i in range(g):
#  with open('W_exp_uq'+str(i)+'.pkl', 'rb') as f:
#    string = 'W'+str(i)
#    var_holder[string] = pickle.load(f)
#    tomostr = 'tomos'+str(i)
#    var_holder[tomostr] = exp2probs(generateData(var_holder[string]), runlabel=None)

#  locals().update(var_holder)
#tomos9
## You'll have W0, W1, W2, ... W999

In [ ]:
#i = 0
#test = {}
#with open('W_exp_uq'+str(i)+'.pkl', 'rb') as f:
#  test = pickle.load(f)

#test